# Credit Card Fraud Prediction

### Import Libraries and Data

In [23]:
import pandas as pd
import numpy as np
import matplotlib.pyplot as plt
#Models
from sklearn.linear_model import LogisticRegression
from sklearn.ensemble import RandomForestClassifier, HistGradientBoostingClassifier
from sklearn.svm import SVC
from sklearn.neighbors import KNeighborsClassifier

In [2]:
df = pd.read_csv('./credit_card_fraud_2026.csv') 
df.set_index('transaction_id', inplace=True)

### EDA

In [3]:
df.head()

,amount_usd,merchant_category,card_type,auth_method,channel,device_type,is_foreign_transaction,hours_since_last_txn,txn_count_last_24h,distance_from_home_km,...,ip_country_mismatch,billing_shipping_mismatch,cvv_retry_count,velocity_score,time_of_day_hour,day_of_week,is_ai_generated_scam_attempt,merchant_risk_score,prior_disputes,is_fraud
transaction_id,,,,,,,,,,,,,,,,,,,,,
1,42.86,Restaurants,Visa,OTP,Online,Android Phone,False,13.54,2,22.35,...,False,False,0,0.1,18,3,False,42.3,0,0
2,4.75,Online Retail,Mastercard,3D Secure,Online,Android Phone,False,0.71,2,35.28,...,False,False,0,25.8,12,4,False,28.3,0,0
3,77.18,Groceries,Mastercard,3D Secure,Online,Mac,False,0.35,5,9.82,...,False,True,0,42.3,5,0,False,24.7,1,0
4,1.69,Streaming,Visa,No Authentication,POS,Android Phone,False,3.42,6,19.72,...,False,False,0,28.9,22,6,False,56.2,1,0
5,261.68,Travel,Visa,3D Secure,In-App,iPhone,False,2.43,2,17.68,...,False,False,0,3.9,2,4,False,32.7,0,0


In [4]:
df.info()

<class 'pandas.core.frame.DataFrame'>
Index: 20000 entries, 1 to 20000
Data columns (total 25 columns):
 #   Column                        Non-Null Count  Dtype  
---  ------                        --------------  -----  
 0   amount_usd                    20000 non-null  float64
 1   merchant_category             20000 non-null  object 
 2   card_type                     20000 non-null  object 
 3   auth_method                   20000 non-null  object 
 4   channel                       20000 non-null  object 
 5   device_type                   20000 non-null  object 
 6   is_foreign_transaction        20000 non-null  bool   
 7   hours_since_last_txn          20000 non-null  float64
 8   txn_count_last_24h            20000 non-null  int64  
 9   distance_from_home_km         20000 non-null  float64
 10  card_age_months               20000 non-null  int64  
 11  customer_age                  20000 non-null  int64  
 12  account_balance_usd           20000 non-null  float64
 13  is_new

In [5]:
df.describe()

,amount_usd,hours_since_last_txn,txn_count_last_24h,distance_from_home_km,card_age_months,customer_age,account_balance_usd,cvv_retry_count,velocity_score,time_of_day_hour,day_of_week,merchant_risk_score,prior_disputes,is_fraud
count,20000.000000,20000.000000,20000.000000,20000.000000,20000.000000,20000.000000,20000.000000,20000.000000,20000.000000,20000.000000,20000.000000,20000.000000,20000.000000,20000.000000
mean,132.424597,8.950827,3.191650,22.139525,46.937550,49.669400,3316.662598,0.181300,19.807735,11.533650,2.998750,37.400390,0.281250,0.016950
std,256.963666,8.838745,1.779544,22.120960,6.768577,18.494032,4350.720948,0.422302,12.366301,6.925335,2.004956,17.061415,0.529209,0.129087
min,1.000000,0.010000,0.000000,0.000000,22.000000,18.000000,52.050000,0.000000,0.000000,0.000000,0.000000,0.000000,0.000000,0.000000
25%,26.235000,2.590000,2.000000,6.337500,42.000000,34.000000,1019.140000,0.000000,10.700000,6.000000,1.000000,25.600000,0.000000,0.000000
50%,57.510000,6.210000,3.000000,15.505000,47.000000,50.000000,2007.685000,0.000000,18.800000,12.000000,3.000000,35.700000,0.000000,0.000000
75%,131.752500,12.432500,4.000000,30.820000,51.000000,66.000000,3944.120000,0.000000,27.600000,18.000000,5.000000,47.300000,0.000000,0.000000
max,6872.690000,87.050000,12.000000,216.190000,74.000000,81.000000,127125.860000,3.000000,74.400000,23.000000,6.000000,100.000000,4.000000,1.000000


In [6]:
#Convert bools in df to 1 and 0
bool_cols = df.select_dtypes(include=["bool"]).columns
df[bool_cols] = df[bool_cols].astype("Int64")

cat_cols = df.select_dtypes(include=["object", "string"]).columns
df_eda = pd.get_dummies(df, columns=cat_cols, dtype=int)
df_eda



,amount_usd,is_foreign_transaction,hours_since_last_txn,txn_count_last_24h,distance_from_home_km,card_age_months,customer_age,account_balance_usd,is_new_merchant,used_vpn,...,channel_Online,channel_POS,device_type_ATM Machine,device_type_Android Phone,device_type_Mac,device_type_POS Terminal,device_type_Smart Watch,device_type_Tablet,device_type_Windows PC,device_type_iPhone
transaction_id,,,,,,,,,,,,,,,,,,,,,
1,42.86,0,13.54,2,22.35,39,25,1080.71,0,0,...,1,0,0,1,0,0,0,0,0,0
2,4.75,0,0.71,2,35.28,47,33,4463.72,1,0,...,1,0,0,1,0,0,0,0,0,0
3,77.18,0,0.35,5,9.82,51,59,366.25,0,1,...,1,0,0,0,1,0,0,0,0,0
4,1.69,0,3.42,6,19.72,48,28,1345.29,1,0,...,0,1,0,1,0,0,0,0,0,0
5,261.68,0,2.43,2,17.68,43,36,4192.59,0,0,...,0,0,0,0,0,0,0,0,0,1
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
19996,41.40,0,8.82,2,18.13,49,20,750.90,0,0,...,0,1,0,1,0,0,0,0,0,0
19997,47.92,0,45.81,1,8.97,41,74,2666.73,0,0,...,0,1,0,1,0,0,0,0,0,0
19998,10.25,0,20.67,0,48.67,40,65,284.25,0,0,...,0,0,0,0,0,0,0,1,0,0


In [7]:
import data_profiling
data_profiling.ProfileReport(df_eda)

Summarize dataset:   0%|          | 0/5 [00:00<?, ?it/s]

100%|██████████| 55/55 [00:00<00:00, 195.68it/s]


Generate report structure:   0%|          | 0/1 [00:00<?, ?it/s]

Render HTML:   0%|          | 0/1 [00:00<?, ?it/s]

### Preprocessing

In [10]:
#Separate features and target variable
X = df.drop(columns='is_fraud')
y = df['is_fraud']

In [30]:
#Split into train, validation, and test sets
from sklearn.model_selection import train_test_split
rs = 42
X_train, X_temp, y_train, y_temp = train_test_split(X, y, test_size=0.3, random_state=rs, stratify=y)
X_val, X_test, y_val, y_test = train_test_split(X_temp, y_temp, test_size=0.5, random_state=rs, stratify=y_temp)
print("Train:", X_train.shape)
print("Validation:", X_val.shape)
print("Test:", X_test.shape)

print("\nClass distribution:")
print(y_train.value_counts(normalize=True))

Train: (14000, 24)
Validation: (3000, 24)
Test: (3000, 24)

Class distribution:
is_fraud
0    0.983071
1    0.016929
Name: proportion, dtype: float64


In [18]:
df.info()

<class 'pandas.core.frame.DataFrame'>
Index: 20000 entries, 1 to 20000
Data columns (total 25 columns):
 #   Column                        Non-Null Count  Dtype  
---  ------                        --------------  -----  
 0   amount_usd                    20000 non-null  float64
 1   merchant_category             20000 non-null  object 
 2   card_type                     20000 non-null  object 
 3   auth_method                   20000 non-null  object 
 4   channel                       20000 non-null  object 
 5   device_type                   20000 non-null  object 
 6   is_foreign_transaction        20000 non-null  Int64  
 7   hours_since_last_txn          20000 non-null  float64
 8   txn_count_last_24h            20000 non-null  int64  
 9   distance_from_home_km         20000 non-null  float64
 10  card_age_months               20000 non-null  int64  
 11  customer_age                  20000 non-null  int64  
 12  account_balance_usd           20000 non-null  float64
 13  is_new

In [28]:
#Transformations to categorical and numeric features
from sklearn.preprocessing import OneHotEncoder, StandardScaler
from sklearn.compose import ColumnTransformer
numeric_cols = X_train.select_dtypes(include=['number']).columns
categorical_cols = X_train.select_dtypes(include=['string', 'object']).columns
print(f'Numeric Columns: {numeric_cols}\n #Columns: {len(numeric_cols)}')
print(f'Categorical Columns: {categorical_cols}\n #Columns: {len(categorical_cols)}')
ct = ColumnTransformer(
    transformers=[
        ('num', StandardScaler(), numeric_cols),
        ('cat', OneHotEncoder(handle_unknown='ignore', sparse_output=False), categorical_cols)]
)

Numeric Columns: Index(['amount_usd', 'is_foreign_transaction', 'hours_since_last_txn',
       'txn_count_last_24h', 'distance_from_home_km', 'card_age_months',
       'customer_age', 'account_balance_usd', 'is_new_merchant', 'used_vpn',
       'ip_country_mismatch', 'billing_shipping_mismatch', 'cvv_retry_count',
       'velocity_score', 'time_of_day_hour', 'day_of_week',
       'is_ai_generated_scam_attempt', 'merchant_risk_score', 'prior_disputes',
       'is_fraud'],
      dtype='object')
 #Columns: 20
Categorical Columns: Index(['merchant_category', 'card_type', 'auth_method', 'channel',
       'device_type'],
      dtype='object')
 #Columns: 5


In [31]:
#Define models
models = {
    "Logistic Regression": LogisticRegression(max_iter=1000, random_state=rs),
    "Random Forest": RandomForestClassifier(n_estimators=300, random_state=rs, n_jobs=1),
    "SVM": SVC(probability=True, random_state=42),
    "KNN": KNeighborsClassifier(),
    "HistGradientBoosting": HistGradientBoostingClassifier(random_state=rs)
}

In [33]:
#Stratified Cross-Validation
from sklearn.model_selection import StratifiedKFold, cross_validate
cv = StratifiedKFold(n_splits=5, shuffle=True, random_state=rs)


In [ ]:
#Make Cross-Validation Pipeline
from imblearn.pipeline import Pipeline
from imblearn.over_sampling import SMOTE

pipelines = {}

for name, model in models.items():
    pipeline = Pipeline([('preprocessor', ct),('smote', SMOTE(random_state=rs)),('model', model)])
    pipelines[name] = pipeline

In [ ]:
#Cross-Validation Score
from sklearn.metrics import accuracy_score, precision_score, recall_score, f1_score, roc_auc_score, classification_report, confusion_matrix
scoring = {
    "accuracy": "accuracy",
    "precision": "precision",
    "recall": "recall",
    "f1": "f1",
    "roc_auc": "roc_auc"
}


In [11]:
df_encoded = pd.DataFrame(model_fit, columns=model.get_feature_names_out(), index=df.index)
df_encoded

,merchant_category_Crypto Exchange,merchant_category_Electronics,merchant_category_Fuel,merchant_category_Gaming,merchant_category_Gift Cards,merchant_category_Groceries,merchant_category_Healthcare,merchant_category_Online Retail,merchant_category_Restaurants,merchant_category_Streaming,...,channel_Online,channel_POS,device_type_ATM Machine,device_type_Android Phone,device_type_Mac,device_type_POS Terminal,device_type_Smart Watch,device_type_Tablet,device_type_Windows PC,device_type_iPhone
transaction_id,,,,,,,,,,,,,,,,,,,,,
1,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,1.0,0.0,...,1.0,0.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0,0.0
2,0.0,0.0,0.0,0.0,0.0,0.0,0.0,1.0,0.0,0.0,...,1.0,0.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0,0.0
3,0.0,0.0,0.0,0.0,0.0,1.0,0.0,0.0,0.0,0.0,...,1.0,0.0,0.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0
4,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,1.0,...,0.0,1.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0,0.0
5,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,...,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,1.0
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
19996,0.0,0.0,0.0,0.0,0.0,0.0,1.0,0.0,0.0,0.0,...,0.0,1.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0,0.0
19997,0.0,0.0,0.0,0.0,0.0,0.0,0.0,1.0,0.0,0.0,...,0.0,1.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0,0.0
19998,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,1.0,0.0,...,0.0,0.0,0.0,0.0,0.0,0.0,0.0,1.0,0.0,0.0


In [12]:
df_ohe = pd.concat([df.drop(columns=categorical_cols), df_encoded], axis=1)
df_ohe

,amount_usd,is_foreign_transaction,hours_since_last_txn,txn_count_last_24h,distance_from_home_km,card_age_months,customer_age,account_balance_usd,is_new_merchant,used_vpn,...,channel_Online,channel_POS,device_type_ATM Machine,device_type_Android Phone,device_type_Mac,device_type_POS Terminal,device_type_Smart Watch,device_type_Tablet,device_type_Windows PC,device_type_iPhone
transaction_id,,,,,,,,,,,,,,,,,,,,,
1,42.86,0,13.54,2,22.35,39,25,1080.71,0,0,...,1.0,0.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0,0.0
2,4.75,0,0.71,2,35.28,47,33,4463.72,1,0,...,1.0,0.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0,0.0
3,77.18,0,0.35,5,9.82,51,59,366.25,0,1,...,1.0,0.0,0.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0
4,1.69,0,3.42,6,19.72,48,28,1345.29,1,0,...,0.0,1.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0,0.0
5,261.68,0,2.43,2,17.68,43,36,4192.59,0,0,...,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,1.0
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
19996,41.40,0,8.82,2,18.13,49,20,750.90,0,0,...,0.0,1.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0,0.0
19997,47.92,0,45.81,1,8.97,41,74,2666.73,0,0,...,0.0,1.0,0.0,1.0,0.0,0.0,0.0,0.0,0.0,0.0
19998,10.25,0,20.67,0,48.67,40,65,284.25,0,0,...,0.0,0.0,0.0,0.0,0.0,0.0,0.0,1.0,0.0,0.0


In [13]:
#Data Scaling
from sklearn.preprocessing import StandardScaler
X = df_ohe[~df_ohe['is_fraud']]
scaler = StandardScaler()
X_scaled = scaler.fit_transform(X)

KeyError: "None of [Index([-1, -1, -1, -1, -1, -1, -1, -1, -1, -1,\n       ...\n       -1, -1, -1, -1, -1, -1, -1, -1, -1, -1],\n      dtype='int64', length=20000)] are in the [columns]"

In [ ]:
#Check completeness
df.isnull().sum()

amount_usd                      0
merchant_category               0
card_type                       0
auth_method                     0
channel                         0
device_type                     0
is_foreign_transaction          0
hours_since_last_txn            0
txn_count_last_24h              0
distance_from_home_km           0
card_age_months                 0
customer_age                    0
account_balance_usd             0
is_new_merchant                 0
used_vpn                        0
ip_country_mismatch             0
billing_shipping_mismatch       0
cvv_retry_count                 0
velocity_score                  0
time_of_day_hour                0
day_of_week                     0
is_ai_generated_scam_attempt    0
merchant_risk_score             0
prior_disputes                  0
is_fraud                        0
dtype: int64

In [ ]:
#Check inconsistencies: Does not appear to be any inconsistencies
df

,amount_usd,merchant_category,card_type,auth_method,channel,device_type,is_foreign_transaction,hours_since_last_txn,txn_count_last_24h,distance_from_home_km,...,ip_country_mismatch,billing_shipping_mismatch,cvv_retry_count,velocity_score,time_of_day_hour,day_of_week,is_ai_generated_scam_attempt,merchant_risk_score,prior_disputes,is_fraud
transaction_id,,,,,,,,,,,,,,,,,,,,,
1,42.86,Restaurants,Visa,OTP,Online,Android Phone,False,13.54,2,22.35,...,False,False,0,0.1,18,3,False,42.3,0,0
2,4.75,Online Retail,Mastercard,3D Secure,Online,Android Phone,False,0.71,2,35.28,...,False,False,0,25.8,12,4,False,28.3,0,0
3,77.18,Groceries,Mastercard,3D Secure,Online,Mac,False,0.35,5,9.82,...,False,True,0,42.3,5,0,False,24.7,1,0
4,1.69,Streaming,Visa,No Authentication,POS,Android Phone,False,3.42,6,19.72,...,False,False,0,28.9,22,6,False,56.2,1,0
5,261.68,Travel,Visa,3D Secure,In-App,iPhone,False,2.43,2,17.68,...,False,False,0,3.9,2,4,False,32.7,0,0
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
19996,41.40,Healthcare,Mastercard,OTP,POS,Android Phone,False,8.82,2,18.13,...,False,False,0,17.3,2,3,False,29.6,1,0
19997,47.92,Online Retail,Visa,OTP,POS,Android Phone,False,45.81,1,8.97,...,False,False,0,9.0,4,0,False,29.2,1,0
19998,10.25,Restaurants,Visa,3D Secure,In-App,Tablet,False,20.67,0,48.67,...,False,False,1,1.0,19,5,False,22.9,0,0
